In [30]:
import json
import jsonpath_ng.ext
from tqdm.notebook import tqdm 
with open('src/WebAnnotationModel-2500-sample-results.json', 'r') as f:
    cont = json.load(f)
    
# taking instances that has the most fields possible
sample = list(filter(lambda s: len(s['body']) > 13, cont))[0]
sample

# JSONPath is nice on theory, but really slow,...

# def extract_value_from_textual_body_with_semantic_prefix(purpose, value, sample):
#     pattern = f'$.body[?(@.type=="TextualBody" & @.purpose=="{purpose}" & @.value =~ "{value}:.*")]'
#     matches = jsonpath_ng.ext.parse(pattern).find(sample)
#     res = [match.value['value'].replace(f'{value}: ', '') for match in matches]
#     if len(res) > 1:
#         raise ValueError(f"Multiple values found for {value}: {res}")
#     return res[0] if res else None

# def extract_value_from_type_with_purpose(tpe, purpose, sample, str_cont = None):
#     if str_cont:
#         pattern = f'$.body[?(@.type=="{tpe}" & @.purpose=="{purpose}" & @.value =~ ".*{str_cont}.*")]'
#     else:
#         pattern = f'$.body[?(@.type=="{tpe}" & @.purpose=="{purpose}")]'
#     matches = jsonpath_ng.ext.parse(pattern).find(sample)
#     res = [match.value['value'] for match in matches]
#     if len(res) > 1:
#         raise ValueError(f"Multiple values found of type {tpe} with purpose {purpose}: {res}")
#     return res[0] if res else None

# def extract_value_from_textual_body_with_purpose(purpose, sample):
#     return extract_value_from_type_with_purpose("TextualBody", purpose, sample)

# def extract_target_img(sample):
#     pattern = '$.target[?(@.type=="Image")]'
#     matches = jsonpath_ng.ext.parse(pattern).find(sample)
#     res = [match.value['source'] for match in matches]
#     if len(res) > 1:
#         raise ValueError(f"Multiple image targets found: {res}")
#     return res[0] if res else None


def extract_value_from_textual_body_with_semantic_prefix(purpose, value, sample):
    bodies = sample['body']
    for b in bodies:
        if b.get('purpose', None) == purpose and b.get('type', None) == 'TextualBody' and b.get('value', '').startswith(f'{value}:'):
            return b.get('value', '').replace(f'{value}: ', '')
    return None 

def extract_value_from_type_with_purpose(tpe, purpose, sample, str_cont = None):
    bodies = sample['body']
    for b in bodies:
        if b.get('type', None) == tpe and b.get('purpose', None) == purpose and (str_cont is None or str_cont in b.get('value', '')):
            return b.get('value', '')
    return None

def extract_value_from_textual_body_with_purpose(purpose, sample):
    return extract_value_from_type_with_purpose("TextualBody", purpose, sample)

def extract_target_img(sample):
    if sample.get('target', {}).get('type', None) == 'Image':
        return sample.get('target', {}).get('id', None)
    return None

def extract_dataset_tavily_results_in_array(sample):
    bodies = sample['body']
    res = []
    for b in bodies:
        if b.get('type', None) == 'Dataset' and b.get('purpose', None) == "searching":
            for entry in b.get('value', []):
                if 'search query' in entry.get('type', ''):
                    res.append('Query: ' + entry.get('value', ''))
                elif 'search result' in entry.get('type', ''):
                    res.append(f"Result: {entry.get('value', '')} - {entry.get('source', '')}")
    return res

def extract_google_search_results(sample):
    bodies = sample['body']
    res = []
    for b in bodies:
        if b.get('type', None) == 'Dataset' and b.get('purpose', None) == "linking":
            for entry in b.get('value', []):
                if 'Partial match' in entry.get('type', ''):
                    res.append(f"Partial match: {entry.get('value', '')} - {entry.get('source', '')}")
                elif 'Full match' in entry.get('type', ''):
                    res.append(f"Full match: {entry.get('value', '')} - {entry.get('source', '')}")
    return res

def extract_google_coordinates(sample):
    pass

json_path_parse_dict = {
    "is_postcard": lambda s: extract_value_from_textual_body_with_semantic_prefix("classifying", "postcard", s),
    "back_postcard": lambda s: extract_value_from_textual_body_with_semantic_prefix("classifying", "postcard's back", s),
    "final_place": lambda s: extract_value_from_textual_body_with_semantic_prefix("identifying", "final_place", s),
    "final_country": lambda s: extract_value_from_textual_body_with_semantic_prefix("identifying", "final_country", s),
    "final_city": lambda s: extract_value_from_textual_body_with_semantic_prefix("identifying", "final_city", s),
    "description": lambda s: extract_value_from_textual_body_with_purpose("describing", s),
    "transcription": lambda s: extract_value_from_textual_body_with_purpose("transcribing", s),
    "date": lambda s: extract_value_from_textual_body_with_purpose("dating", s),
    "europeana_link": lambda s: extract_value_from_type_with_purpose("SpecificResource", "linking", s, "europeana.eu"),
    "reason": lambda s: extract_value_from_textual_body_with_purpose("commenting", s),
    "img_src": extract_target_img,
    "tavily": extract_dataset_tavily_results_in_array,
    "google_search": extract_google_search_results,
}


sampled_values = []
for s in tqdm(cont):
    vals = {}
    for k, v in json_path_parse_dict.items():
        vals[k] = v(s)
    sampled_values.append(vals)

  0%|          | 0/2616 [00:00<?, ?it/s]

In [31]:
sampled_values

[{'is_postcard': 'yes',
  'back_postcard': None,
  'final_place': 'Fosselven Elektrisitetsverk',
  'final_country': 'Norway',
  'final_city': 'Tangen',
  'description': "The image shows a historical black-and-white photograph of a brick industrial building located beside a small river or stream, surrounded by trees and forested hills. There are two people visible near the building, and the architecture suggests early 20th-century construction. The text on the image identifies the building as an electricity works and provides a date and photographer's name.",
  'transcription': '1460 VIKSELVEN ELEKTRISITETSVERK. Enerat 1922 Carl Normann Hamar.',
  'date': '1920s',
  'europeana_link': 'https://www.europeana.eu/item/753/_011012780813',
  'reason': "The text is in Norwegian and references an electricity works ('Elektrisitetsverk'), with the name 'Vikselven' suggesting a Norwegian river. The photographer, Carl Normann, is a known Norwegian postcard publisher. The date 1922 and the overall s

In [29]:
sampled_values

[{'is_postcard': 'yes',
  'back_postcard': None,
  'final_place': 'Fosselven Elektrisitetsverk',
  'final_country': 'Norway',
  'final_city': 'Tangen',
  'description': "The image shows a historical black-and-white photograph of a brick industrial building located beside a small river or stream, surrounded by trees and forested hills. There are two people visible near the building, and the architecture suggests early 20th-century construction. The text on the image identifies the building as an electricity works and provides a date and photographer's name.",
  'transcription': '1460 VIKSELVEN ELEKTRISITETSVERK. Enerat 1922 Carl Normann Hamar.',
  'date': '1920s',
  'europeana_link': 'https://www.europeana.eu/item/753/_011012780813',
  'reason': "The text is in Norwegian and references an electricity works ('Elektrisitetsverk'), with the name 'Vikselven' suggesting a Norwegian river. The photographer, Carl Normann, is a known Norwegian postcard publisher. The date 1922 and the overall s

In [24]:
sampled_values

[{'is_postcard': 'yes',
  'back_postcard': None,
  'final_place': 'Fosselven Elektrisitetsverk',
  'final_country': 'Norway',
  'final_city': 'Tangen',
  'description': "The image shows a historical black-and-white photograph of a brick industrial building located beside a small river or stream, surrounded by trees and forested hills. There are two people visible near the building, and the architecture suggests early 20th-century construction. The text on the image identifies the building as an electricity works and provides a date and photographer's name.",
  'transcription': '1460 VIKSELVEN ELEKTRISITETSVERK. Enerat 1922 Carl Normann Hamar.',
  'date': '1920s',
  'europeana_link': 'https://www.europeana.eu/item/753/_011012780813',
  'reason': "The text is in Norwegian and references an electricity works ('Elektrisitetsverk'), with the name 'Vikselven' suggesting a Norwegian river. The photographer, Carl Normann, is a known Norwegian postcard publisher. The date 1922 and the overall s

In [38]:
cont

[{'@context': 'http://www.w3.org/ns/anno.jsonld',
  'type': 'Annotation',
  'id': 'https://timeatlas.eu/annotation/_011012780813',
  'generated': '2025-09-25T14:12:58.344548',
  'target': {'type': 'Image',
   'id': 'https://pdms.dimu.org/image/04SW7f1S8x?dimension=1200x1200'},
  'body': [{'type': 'TextualBody',
    'purpose': 'classifying',
    'value': 'postcard: yes'},
   {'type': 'TextualBody',
    'purpose': 'identifying',
    'value': 'final_place: Fosselven Elektrisitetsverk'},
   {'type': 'TextualBody',
    'purpose': 'identifying',
    'value': 'final_country: Norway'},
   {'type': 'TextualBody',
    'purpose': 'identifying',
    'value': 'final_city: Tangen'},
   {'type': 'TextualBody',
    'purpose': 'describing',
    'value': "The image shows a historical black-and-white photograph of a brick industrial building located beside a small river or stream, surrounded by trees and forested hills. There are two people visible near the building, and the architecture suggests early 2